# 05A - Generating QA

In [1]:
import json
import re
import time
import hashlib
import datetime
import logging
import os
from collections import defaultdict
from openai import OpenAI
from tqdm.auto import tqdm

## 1. Konfigurasi

In [2]:
CONFIG = {
    "input_dir":               "/kaggle/input/notebooks/muhammadnabilul/04-chunking-and-splitting/chunks",
    "output_dir":              "output_05a",
    "llm_model":               "deepseek-v4-flash",
    "llm_temperature_qa":      0.7,
    "llm_temperature_summary": 0.3,
    "max_completion_summary":  700,
    "max_tokens_per_context":  1500,
    "overlap_tokens":          150,
    "dataset_version":         "v1.0",
    "retry_attempts":          3,
    "retry_delay":             2.0,
    "request_delay":           1.0,
    "checkpoint_interval":     100,
    "preview_interval":        10,
    "min_section_tokens":      100,
    "max_sections_per_doc":    23,
    "skip_section_sources":    {"lampiran", "prolog"},
    "test_mode":               False,
    "max_documents_test":      None,
 
    "system_prompt_qa": (
        "Anda sedang membangun Context-Grounded Instruction Dataset untuk melatih Small Language "
        "Model (SLM) sebagai komponen generator dalam sistem Retrieval-Augmented Generation (RAG) "
        "publikasi statistik BPS.\n\n"
        "FILOSOFI DATASET\n"
        "Setiap pasangan yang Anda buat bukan sekadar QA — ini adalah interaction yang melatih "
        "model membaca, memahami, dan mengintegrasikan informasi dari teks sumber yang diterima "
        "retriever. Instruction tidak selalu pertanyaan: bisa berupa permintaan penjelasan, "
        "perbandingan, uraian, atau pencarian ('Jelaskan...', 'Bandingkan...', 'Di mana saya "
        "dapat menemukan...', 'Saya ingin mengetahui...'). Response melatih model menjawab "
        "HANYA dari teks sumber, tanpa pengetahuan luar.\n\n"
        "ATURAN WAJIB\n"
        "1. Semua fakta, angka, dan klaim dalam response HARUS didukung eksplisit oleh teks sumber.\n"
        "2. Dilarang mereferensikan wadah retrieval: 'konteks ini', 'bagian ini', 'passages', "
        "'teks sumber ini', 'teks sumber', 'di atas', atau 'dokumen ini'. Instruction dan response "
        "harus berdiri sendiri. Atribusi "
        "ke sumber dunia nyata DIPERBOLEHKAN bila natural (mis. 'menurut Susenas 2024', "
        "'berdasarkan data BPS'), bersifat OPSIONAL — jangan jadikan awalan wajib yang "
        "menyeragamkan setiap jawaban atau membuat response bertele-tele.\n"
        "3. Setiap interaction membahas sub-topik BERBEDA dari teks sumber.\n"
        "4. Instruction WAJIB spesifik — tidak bisa dijawab tanpa membaca teks sumber.\n"
        "5. Pertahankan istilah teknis BPS persis (Susenas, garis kemiskinan, TPT, IPM, PDRB, dll).\n"
        "6. Dilarang membuat interaction yang membutuhkan pembacaan sel tabel atau isi visual, "
        "termasuk urutan angka pada keterangan grafik/gambar.\n"
        "7. Abaikan baris yang didominasi karakter pipe ('|'), serta urutan angka pada keterangan "
        "grafik/gambar yang berderet tanpa pemisah desimal jelas (mis. '759 7,61 746') — "
        "keduanya artefak linearisasi ekstraksi PDF, bukan narasi; jangan dijadikan sumber "
        "fakta atau angka kecuali maknanya benar-benar tidak ambigu.\n"
        "8. ATURAN NUMERIK (berlaku hanya untuk factual_retrieval, trend_interpretation, "
        "comparative_analysis): bila teks sumber memuat angka (indikator/indeks/persentase/nilai), "
        "instruction dan response WAJIB memuat angka spesifik tersebut, bukan parafrase "
        "kualitatif. Tidak dipaksakan pada tipe definisional/metodologis. Untuk angka TURUNAN "
        "(selisih, pertumbuhan, rata-rata): HANYA boleh dihitung jika KEDUA angka sumber "
        "tampil eksplisit di teks sumber. DILARANG membalik-hitung salah satu angka sumber dari "
        "klaim selisih/pertumbuhan yang tidak eksplisit — jika salah satu sisi tidak tersedia, "
        "JANGAN buat perbandingan tersebut sama sekali.\n"
        "9. Response WAJIB berupa pernyataan final yang percaya diri. DILARANG menyisipkan catatan "
        "proses berpikir, asumsi, atau ketidakpastian dalam tanda kurung (mis. '(tidak disebut "
        "eksplisit, dihitung dari...)', '(estimasi)', '(kemungkinan)'). Jika sebuah angka atau "
        "klaim tidak bisa dipastikan dari teks sumber, JANGAN sertakan klaim tersebut sama sekali.\n"
        "10. Field 'type' WAJIB salah satu nilai yang disebutkan di pesan pengguna.\n\n"
        "CONTOH (BENAR vs SALAH)\n"
        "[factual_retrieval — aturan numerik #8]\n"
        "SALAH: instruction='Bagaimana kondisi ketenagakerjaan Jabar?' "
        "response='Ketenagakerjaan Jabar mengalami peningkatan yang cukup baik.'\n"
        "BENAR: instruction='Berapa Tingkat Pengangguran Terbuka (TPT) Jawa Barat?' "
        "response='TPT Jawa Barat tercatat sebesar 7,44 persen.'\n"
        "[source_navigation — letak, bukan isi tabel, aturan #6]\n"
        "SALAH: instruction='Apa isi Tabel 3.2?' response='Tabel 3.2 menunjukkan angka 12,3 pada baris pertama.'\n"
        "BENAR: instruction='Di bagian mana pembahasan mengenai garis kemiskinan perkotaan dapat ditemukan?' "
        "response='Pembahasan garis kemiskinan perkotaan terdapat pada subbab Kemiskinan, dirujuk melalui Tabel 3.2.'\n"
        "[meta-talk vs atribusi — aturan #2]\n"
        "SALAH: response='Berdasarkan dokumen ini, IPM meningkat.'\n"
        "BENAR (atribusi opsional, natural): response='Menurut data BPS, IPM meningkat menjadi 74,5 pada 2024.'\n"
        "BENAR (tanpa atribusi, tetap sah): response='IPM meningkat menjadi 74,5 pada 2024.'\n"
        "[angka turunan — aturan #8]\n"
        "SALAH: response='...turun dari 72,60 poin (tidak disebut eksplisit, dihitung dari 58,68+13,92) menjadi 58,68 poin.'\n"
        "BENAR (kedua sisi eksplisit ada di teks sumber): response='IPM DKI Jakarta 81,65 dan IPM Papua 61,39, selisih keduanya 20,26 poin.'\n"
        "BENAR (salah satu sisi tidak eksplisit ada → jangan buat perbandingan itu): pilih sub-topik lain yang kedua angkanya lengkap.\n"
        "[catatan proses berpikir — aturan #9]\n"
        "SALAH: response='Nilainya sekitar 70 poin (estimasi, tidak disebutkan pasti).'\n"
        "BENAR: hilangkan klaim tersebut sepenuhnya jika angka pastinya tidak ada di teks sumber.\n\n"
        "OUTPUT: JSON array valid, tanpa markdown, tanpa teks lain.\n"
        "[\n"
        "  {\n"
        "    \"task\": \"qa\",\n"
        "    \"type\": \"<salah satu type yang diizinkan>\",\n"
        "    \"instruction\": \"<interaction natural — bisa pertanyaan atau permintaan>\",\n"
        "    \"response\": \"<jawaban lengkap berbasis teks sumber>\",\n"
        "    \"reasoning_source\": \"<single_paragraph|multi_paragraph|whole_section>\",\n"
        "    \"context_focus\": \"<deskripsi singkat sub-topik>\"\n"
        "  }\n"
        "]"
    ),
 
    "system_prompt_summary": (
        "Anda sedang membangun Context-Grounded Instruction Dataset untuk melatih Small Language "
        "Model (SLM) komponen generator sistem RAG publikasi statistik BPS.\n\n"
        "TUGAS\n"
        "Buat 1 pasangan interaction-response tipe 'document_overview'. "
        "Pasangan ini melatih SLM mensintesis seluruh teks sumber yang diterima retriever.\n\n"
        "ATURAN WAJIB\n"
        "1. Instruction berupa permintaan gambaran menyeluruh yang natural dan spesifik — bukan generik. "
        "Contoh: 'Apa gambaran umum...', 'Uraikan temuan utama mengenai...', "
        "'Jelaskan secara komprehensif pembahasan tentang...'.\n"
        "2. Response WAJIB mensintesis informasi dari AWAL, TENGAH, dan AKHIR teks sumber.\n"
        "3. Sertakan minimal 2 indikator atau temuan spesifik dari teks sumber.\n"
        "4. Dilarang mereferensikan wadah retrieval ('bagian ini', 'dokumen ini', 'passages', "
        "'teks sumber ini', 'di atas'). Atribusi ke sumber dunia nyata (mis. 'data BPS') "
        "OPSIONAL dan tidak wajib.\n"
        "5. Abaikan baris yang didominasi karakter pipe ('|') — artefak linearisasi tabel, "
        "bukan narasi; jangan dijadikan sumber fakta atau angka.\n"
        "6. Semua fakta HARUS ada di teks sumber.\n"
        "7. Response WAJIB berupa pernyataan final yang percaya diri. DILARANG menyisipkan "
        "catatan proses berpikir, asumsi, atau ketidakpastian dalam tanda kurung "
        "(mis. '(tidak disebut eksplisit, dihitung dari...)', '(estimasi)'). Jika sebuah "
        "indikator tidak bisa dipastikan dari teks sumber, JANGAN sertakan dalam sintesis.\n\n"
        "CONTOH (BENAR vs SALAH)\n"
        "SALAH (generik, tidak sintesis, hanya awal): instruction='Apa isi dokumen ini?' "
        "response='Dokumen ini membahas ketenagakerjaan secara umum.'\n"
        "BENAR: instruction='Uraikan temuan utama mengenai ketenagakerjaan Jawa Barat tahun 2024.' "
        "response='TPT Jawa Barat tercatat 7,44 persen, didorong oleh perlambatan sektor "
        "manufaktur pada awal tahun. Di pertengahan periode, tercatat pergeseran tenaga kerja "
        "ke sektor informal. Menjelang akhir tahun, tingkat partisipasi angkatan kerja tercatat "
        "67,2 persen, menunjukkan pemulihan bertahap.'\n\n"
        "OUTPUT: JSON array valid, tanpa markdown, tanpa teks lain.\n"
        "[\n"
        "  {\n"
        "    \"task\": \"summary\",\n"
        "    \"type\": \"document_overview\",\n"
        "    \"instruction\": \"<permintaan gambaran menyeluruh yang natural>\",\n"
        "    \"response\": \"<sintesis komprehensif dari seluruh teks sumber>\",\n"
        "    \"reasoning_source\": \"whole_section\",\n"
        "    \"context_focus\": \"<deskripsi topik keseluruhan>\"\n"
        "  }\n"
        "]"
    ),
}
 
QA_BATCHES = [
    {
        "pattern":          "literal_reading",
        "allowed_types":    "factual_retrieval, source_navigation",
        "focus": (
            "Reasoning pattern: LITERAL READING — membaca dan menemukan informasi yang tertulis "
            "eksplisit di teks sumber.\n"
            "Tipe yang diizinkan: factual_retrieval ATAU source_navigation.\n"
            "- factual_retrieval: interaction meminta fakta, angka, atau pernyataan eksplisit "
            "yang tertulis langsung di narasi.\n"
            "- source_navigation: interaction meminta LOKASI atau rujukan — di subbab/bagian mana "
            "suatu topik dibahas, atau tabel/gambar nomor berapa yang membahasnya. Menunjuk "
            "keberadaan/letak, BUKAN membaca isi sel tabel.\n"
            "Hasilkan {n_pairs} interaction. Setiap interaction membahas sub-topik BERBEDA dari "
            "bagian BERBEDA dalam narasi. Usahakan kedua tipe terwakili minimal 1 kali; sisanya bebas."
        ),
        "generation_focus": "literal_reading",
    },
    {
        "pattern":          "concept_understanding",
        "allowed_types":    "definition_clarification, methodology_explanation",
        "focus": (
            "Reasoning pattern: CONCEPT UNDERSTANDING — memahami makna istilah dan metodologi.\n"
            "Tipe yang diizinkan: definition_clarification ATAU methodology_explanation.\n"
            "- definition_clarification: interaction meminta penjelasan istilah, konsep, atau "
            "indikator statistik yang didefinisikan dalam narasi.\n"
            "- methodology_explanation: interaction meminta penjelasan cara pengukuran, metode "
            "pengumpulan data, atau formula yang dijelaskan dalam narasi.\n"
            "Hasilkan {n_pairs} interaction. Setiap interaction dari sub-topik BERBEDA. "
            "Usahakan kedua tipe terwakili minimal 1 kali; sisanya bebas."
        ),
        "generation_focus": "concept_understanding",
    },
    {
        "pattern":          "evidence_integration",
        "allowed_types":    "trend_interpretation, causal_reasoning",
        "focus": (
            "Reasoning pattern: EVIDENCE INTEGRATION — menginterpretasikan bukti dan menalar sebab-akibat.\n"
            "Tipe yang diizinkan: trend_interpretation ATAU causal_reasoning.\n"
            "- trend_interpretation: interaction meminta interpretasi pola, perubahan, atau "
            "dinamika dari data (naik/turun/stabil, mengapa berfluktuasi).\n"
            "- causal_reasoning: interaction meminta penjelasan penyebab, dampak, atau "
            "implikasi dari fenomena yang dibahas dalam narasi.\n"
            "Hasilkan {n_pairs} interaction. Berbasis bukti dari bagian BERBEDA dalam narasi. "
            "Usahakan kedua tipe terwakili minimal 1 kali; sisanya bebas."
        ),
        "generation_focus": "evidence_integration",
    },
    {
        "pattern":          "analytical_reasoning",
        "allowed_types":    "comparative_analysis, multi_source_synthesis",
        "focus": (
            "Reasoning pattern: ANALYTICAL REASONING — membandingkan dan mensintesis lintas informasi.\n"
            "Tipe yang diizinkan: comparative_analysis ATAU multi_source_synthesis.\n"
            "- comparative_analysis: interaction meminta perbandingan eksplisit antara dua atau "
            "lebih entitas (wilayah, periode, kelompok, indikator) menggunakan data di narasi.\n"
            "- multi_source_synthesis: interaction membutuhkan penggabungan informasi dari "
            "MINIMAL DUA bagian berbeda. reasoning_source WAJIB multi_paragraph atau whole_section.\n"
            "Hasilkan {n_pairs} interaction dari 2 tipe BERBEDA."
        ),
        "generation_focus": "analytical_reasoning",
    },
]
 
ALLOWED_TASKS = {"qa", "summary"}
ALLOWED_SUBTASKS = {
    "factual_retrieval", "source_navigation",
    "definition_clarification", "methodology_explanation",
    "trend_interpretation", "causal_reasoning",
    "comparative_analysis", "multi_source_synthesis",
    "document_overview",
}
 
def get_n_pairs(context_token_count):
    if context_token_count < 1200:
        return 2
    elif context_token_count <= 2200:
        return 4
    return 6
 
def get_max_completion_qa(n_pairs):
    return (n_pairs + 1) * 400
 
from kaggle_secrets import UserSecretsClient
user_secrets = UserSecretsClient()
api_key = user_secrets.get_secret("API_Deepseek")
client = OpenAI(api_key=api_key, base_url="https://api.deepseek.com")
 
GENERATION_TIMESTAMP = datetime.datetime.now(datetime.timezone.utc).isoformat(timespec="seconds")
 
os.makedirs(CONFIG["output_dir"], exist_ok=True)
os.makedirs(f"{CONFIG['output_dir']}/logs", exist_ok=True)
 
OUT                   = CONFIG["output_dir"]
RAW_JSONL             = f"{OUT}/raw_records.jsonl"
FAILURES_JSONL        = f"{OUT}/generation_failures.jsonl"
PROCESSED_UNITS_JSONL = f"{OUT}/processed_units.jsonl"

### a. Logging

In [3]:
def setup_logger(name, filepath):
    handler = logging.FileHandler(filepath, encoding="utf-8")
    handler.setFormatter(logging.Formatter("%(asctime)s %(levelname)s %(message)s"))
    logger = logging.getLogger(name)
    logger.setLevel(logging.INFO)
    logger.addHandler(handler)
    return logger
 
# Logger untuk alur normal generate
gen_log  = setup_logger("generation", f"{OUT}/logs/generation.log")
# Logger cadangan khusus kegagalan (saat ini kegagalan juga ditulis ke JSONL)
fail_log = setup_logger("failure",    f"{OUT}/logs/failure.log")

### b. Checkpoint

In [4]:
def load_jsonl(filepath):
    if not os.path.exists(filepath):
        return []
    records = []
    with open(filepath, "r", encoding="utf-8") as f:
        for line in f:
            line = line.strip()
            if line:
                records.append(json.loads(line))
    return records
 
# Buka file dalam mode append (tidak menimpa data lama)
# Tulis satu record per baris
def append_jsonl(filepath, records):
    with open(filepath, "a", encoding="utf-8") as f:
        for rec in records:
            f.write(json.dumps(rec, ensure_ascii=False) + "\n")
        f.flush()
        os.fsync(f.fileno())
 
# satu jendela konteks × satu jenis generate (QA-batch-0/1 atau summary)
def unit_key(document_title, section_id, batch_idx, generation_focus):
    return f"{document_title}|{section_id}|b{batch_idx}|{generation_focus}"
 
# Baca semua kunci unit yang sudah selesai dari file resume ke dalam set
def load_completed_units():
    return {r["k"] for r in load_jsonl(PROCESSED_UNITS_JSONL)}
 
# Tambahkan satu kunci ke file resume; dipanggil setelah unit selesai 
def mark_unit(key):
    append_jsonl(PROCESSED_UNITS_JSONL, [{"k": key}])

## 2. Fungsi Persiapan

### a. Chunks ke section

In [5]:
# Urutkan nama file agar urutan pemrosesan konsisten antar run
def load_chunks(input_dir):
    chunks = []
    json_files = sorted(f for f in os.listdir(input_dir) if f.endswith(".json"))
    for fname in json_files:
        fpath = os.path.join(input_dir, fname)
        with open(fpath, "r", encoding="utf-8") as f:
            data = json.load(f)
        if isinstance(data, list):
            chunks.extend(data)
        else:
            chunks.append(data)
    gen_log.info(f"Loaded {len(chunks)} chunks from {len(json_files)} files")
    return chunks

In [6]:
# Membalik proses chunking: kelompokkan chunk kembali ke section induknya
# Kunci unik section: kombinasi judul dokumen + ID section
def reconstruct_sections(chunks_data):
    sections = {}
    for chunk in chunks_data:
        sec_key = (chunk.get("document_title"), chunk.get("section_id"))
        if sec_key not in sections:
            sections[sec_key] = {
                "section_title":      chunk.get("section_title"),
                "section_id":         chunk.get("section_id"),
                "section_source":     chunk.get("section_source", ""),
                "document_title":     chunk.get("document_title"),
                "document_year":      chunk.get("document_year"),
                "bps_url":            chunk.get("bps_url"),
                "section_chunks":     [],
                "section_token_est":  0,
            }
        sections[sec_key]["section_chunks"].append({
            "chunk_id":      chunk["chunk_id"],
            "text":          chunk.get("text", ""),
            "chunk_type":    chunk.get("chunk_type", "text_only"),
            "token_estimate": chunk.get("token_estimate", 0),
            "page_start":    chunk.get("chunk_page_start", 0),
            "page_end":      chunk.get("chunk_page_end", 0),
        })
        sections[sec_key]["section_token_est"] += chunk.get("token_estimate", 0)
    return sections
 
 
def _is_noise_title(title):
    # Judul kosong/None selalu dianggap noise 
    if not title:
        return True
    # Hitung karakter non-ASCII atau simbol artefak ekstraksi PDF    
    non_ascii = sum(1 for ch in title if ord(ch) > 127 or ch in "©®™|=\\")
    # Jika lebih dari 15% karakter adalah noise → judul tidak valid
    return non_ascii / max(len(title), 1) > 0.15
 
# Filter
def filter_section(sec_data):
    # Tolak: section berasal dari sumber yang selalu dilewati
    if sec_data["section_source"] in CONFIG["skip_section_sources"]:
        return False, "bad_source"
    # Tolak: section terlalu pendek untuk menghasilkan QA berkualitas    
    if sec_data["section_token_est"] < CONFIG["min_section_tokens"]:
        return False, "too_short"
    # Tolak: semua chunk hanya tabel atau gambar (tidak ada narasi teks)    
    if all(c["chunk_type"] in ("table_rich", "figure_rich") for c in sec_data["section_chunks"]):
        return False, "all_non_text"
    # Tolak: judul section mengandung terlalu banyak karakter noise PDF
    if _is_noise_title(sec_data.get("section_title", "")):
        return False, "noise_title"
    return True, "ok"
 
 
def select_sections(sections):
    # Kelompokkan per dokumen
    by_doc = defaultdict(list)
    for sec_key, sec_data in sections.items():
        lolos, reason = filter_section(sec_data)
        if lolos:
            by_doc[sec_data["document_title"]].append((sec_key, sec_data))
 
    selected = {}
    filter_stats = defaultdict(int)
 
    # Hitung yang difilter
    for sec_key, sec_data in sections.items():
        lolos, reason = filter_section(sec_data)
        if not lolos:
            filter_stats[reason] += 1
 
    cap = CONFIG["max_sections_per_doc"]
    for doc_title, sec_list in by_doc.items():
        # Prioritas: section dengan token terbanyak (paling substansial) diproses duluan
        sec_list.sort(key=lambda x: x[1]["section_token_est"], reverse=True)
        # Ambil maksimal `cap` section per dokumen untuk keseimbangan dataset
        for sec_key, sec_data in sec_list[:cap]:
            selected[sec_key] = sec_data
 
    gen_log.info(
        f"Section selection: raw={len(sections)} | "
        f"filtered={sum(filter_stats.values())} ({dict(filter_stats)}) | "
        f"selected={len(selected)}"
    )
    return selected, dict(filter_stats)

### b. Overlap Batching

In [7]:
# Estimasi kasar: jumlah kata × 1.35 (konsisten dengan Notebook 04)
def _estimate_tokens(text):
    return max(1, int(len(text.split()) * 1.35))
 
def batch_section(section_chunks, max_tokens, overlap_tokens):
    # Section kosong tidak menghasilkan batc
    if not section_chunks:
        return []
 
    step = max_tokens - overlap_tokens
 
    # Buat word-stream dengan provenance per chunk
    word_stream = []
    for sc in section_chunks:
        # Daftar nomor halaman yang dicakup chunk ini
        pages = list(range(sc["page_start"], sc["page_end"] + 1))
        for word in sc["text"].split():
            # Setiap kata membawa metadata sumbernya
            word_stream.append({"word": word, "chunk_id": sc["chunk_id"], "pages": pages})
 
    if not word_stream:
        return []
 
    # Konversi max_tokens dan step ke jumlah kata (1 token ≈ 0.74 kata)
    words_per_token = 0.74
    max_words  = int(max_tokens * words_per_token)
    step_words = int(step * words_per_token)
 
    batches = []
    pos = 0
 
    while pos < len(word_stream):
        # Ambil potongan sepanjang max_words kata
        window = word_stream[pos: pos + max_words]
 
        # Kumpulkan chunk_id unik dalam urutan kemunculan (union provenance)
        chunk_ids_seen = []
        chunk_id_set   = set()
        # Kumpulkan semua nomor halaman yang tercakup jendela ini
        pages_seen     = set()
 
        for w in window:
            if w["chunk_id"] not in chunk_id_set:
                chunk_ids_seen.append(w["chunk_id"])
                chunk_id_set.add(w["chunk_id"])
            pages_seen.update(w["pages"])
 
        # Gabungkan kata-kata jendela menjadi satu teks konteks
        context_text = " ".join(w["word"] for w in window)
        token_count  = _estimate_tokens(context_text)
 
        batches.append({
            "context_text":        context_text,
            # Daftar chunk_id sumber (untuk `retrieval_evaluable` test set)
            "context_chunk_ids":   chunk_ids_seen,
            # Halaman sumber terurut (untuk provenance sitasi)
            "source_pages":        sorted(list(pages_seen)),
            "context_token_count": token_count,
        })
 
        pos += step_words
 
    return batches

### c. json parse

In [8]:
def safe_json_parse(raw):
    raw = raw.strip()
 
    # Tahap 1: parse langsung 
    try:
        result = json.loads(raw)
        if isinstance(result, list):
            return result, "direct"
    except json.JSONDecodeError:
        pass
 
    # Tahap 2: hapus pembungkus fenced code block
    cleaned = re.sub(r"^```(?:json)?\s*", "", raw, flags=re.IGNORECASE)
    cleaned = re.sub(r"\s*```$", "", cleaned).strip()
    try:
        result = json.loads(cleaned)
        if isinstance(result, list):
            return result, "fence_stripped"
    except json.JSONDecodeError:
        pass
 
    # Tahap 3: ekstraksi iteratif substring [...]
    for i, ch in enumerate(cleaned):
        if ch == "[":
            for j in range(len(cleaned), i, -1):
                if cleaned[j - 1] == "]":
                    try:
                        result = json.loads(cleaned[i:j])
                        if isinstance(result, list):
                            return result, "extracted"
                    except json.JSONDecodeError:
                        continue
 
    return None, "failed"

### d. Generate logic

In [9]:
import asyncio
 
class BudgetExhausted(Exception):
    pass
 
 
def call_llm(system_prompt, user_content, temperature, max_completion, label=""):
    last_error = ""
    for attempt in range(1, CONFIG["retry_attempts"] + 1):
        try:
            response = client.chat.completions.create(
                model=CONFIG["llm_model"],
                temperature=temperature,
                max_tokens=max_completion,
                extra_body={"thinking": {"type": "disabled"}},
                messages=[
                    {"role": "system", "content": system_prompt},
                    {"role": "user",   "content": user_content},
                ],
            )
            raw    = response.choices[0].message.content or ""
            finish = response.choices[0].finish_reason
            usage  = response.usage
            usage_dict = usage.model_dump() if hasattr(usage, "model_dump") else dict(usage)
            cached = (
                usage_dict.get("prompt_cache_hit_tokens")
                or usage_dict.get("prompt_tokens_cached")
                or (usage_dict.get("prompt_tokens_details") or {}).get("cached_tokens")
                or 0
            )
            if finish == "length":
                gen_log.warning(f"[{label}] output truncated")
            parsed, parse_status = safe_json_parse(raw)
            if parsed is None:
                gen_log.warning(f"[{label}] parse={parse_status} finish={finish} raw={repr(raw[:200])}")
            return parsed, parse_status, raw, {
                "prompt_tokens":     usage.prompt_tokens,
                "completion_tokens": usage.completion_tokens,
                "total_tokens":      usage.total_tokens,
                "cached_tokens":     cached,
            }
        except Exception as e:
            last_error = str(e)
            gen_log.warning(f"[{label}] attempt {attempt} error: {e}")
            print(f"  [ERR ] {label} attempt {attempt}: {str(e)[:120]}")
            if any(kw in str(e).lower() for kw in ["insufficient", "balance", "402"]):
                raise BudgetExhausted(str(e)) from e
            if attempt < CONFIG["retry_attempts"]:
                wait = CONFIG["retry_delay"] * attempt
                if "429" in str(e):
                    wait = max(wait, 60)
                    print(f"  [WAIT] rate limit, tunggu {wait:.0f}s...")
                time.sleep(wait)
    gen_log.error(f"[{label}] all attempts failed: {last_error}")
    return None, "api_error", "", {
        "prompt_tokens": 0, "completion_tokens": 0, "total_tokens": 0, "cached_tokens": 0,
    }
 
 
async def call_llm_async(system_prompt, user_content, temperature, max_completion, label=""):
    loop = asyncio.get_event_loop()
    return await loop.run_in_executor(
        None,
        lambda: call_llm(system_prompt, user_content, temperature, max_completion, label)
    )
 
 
async def generate_all_qa_parallel(context_text, ctx_token_count, batch_label):
    n_pairs  = get_n_pairs(ctx_token_count)
    max_comp = get_max_completion_qa(n_pairs)
    sys_prompt = CONFIG["system_prompt_qa"]
    tasks = []
    for qa_cfg in QA_BATCHES:
        focus_resolved = qa_cfg["focus"].replace("{n_pairs}", str(n_pairs))
        user_content = (
            f"Dokumen Referensi:\n{context_text}\n\n"
            f"Hasilkan {n_pairs} interaction. "
            f"Reasoning pattern: {qa_cfg['pattern']}. "
            f"Type yang diizinkan: {qa_cfg['allowed_types']}.\n"
            f"{focus_resolved}"
        )
        label = f"{batch_label}|{qa_cfg['generation_focus']}"
        tasks.append(call_llm_async(sys_prompt, user_content, CONFIG["llm_temperature_qa"], max_comp, label=label))
    results = await asyncio.gather(*tasks, return_exceptions=True)
    return results, n_pairs
 
 
def generate_summary(context_text, section_title, label=""):
    user_content = f"Topik: {section_title}\n\nDokumen Referensi:\n{context_text}"
    return call_llm(
        CONFIG["system_prompt_summary"], user_content,
        CONFIG["llm_temperature_summary"], CONFIG["max_completion_summary"], label=label,
    )

### e. record ID

In [10]:
# Rakit payload dari semua field yang menjadi identitas unik record
def make_record_id(instruction, response, document_title, section_title, context_hash):
    payload = f"{instruction}|{response}|{document_title}|{section_title}|{context_hash}"
    return hashlib.sha256(payload.encode()).hexdigest()[:16]

### f. Proses batch

In [11]:
def print_preview(records, batch_label):
    if not records:
        return
    rec = records[0]
    sep = "─" * 60
    print(f"\n{sep}")
    print(f"PREVIEW  {batch_label}")
    print(f"  doc    : {rec['document_title'][:55]}")
    print(f"  section: {rec['section_title'][:55]}")
    print(f"  pattern: {rec['generation_focus']} | subtask: {rec['subtask_type']}")
    print(f"  source : {rec['reasoning_source']} | focus: {rec['context_focus']}")
    print(f"  Q: {rec['instruction']}")
    print(f"  A: {rec['response'][:300]}{'...' if len(rec['response']) > 300 else ''}")
    print(sep)
 
 
def process_batch(batch, batch_idx, num_batches, data, ctx_hash,
                  parsed, parse_status, generation_focus, usage):
    records, skipped = [], 0
    for item in parsed:
        instruction     = item.get("instruction", "").strip()
        response        = item.get("response", "").strip()
        task_type       = item.get("task", "").strip()
        subtask_type    = item.get("type", "").strip()
        reasoning_source = item.get("reasoning_source", "").strip()
        context_focus   = item.get("context_focus", "").strip()
 
        if not instruction or not response:
            skipped += 1; continue
        if task_type not in ALLOWED_TASKS:
            skipped += 1; continue
        if subtask_type not in ALLOWED_SUBTASKS:
            gen_log.warning(f"invalid subtask={subtask_type} in {data['section_id']}|{generation_focus}")
            skipped += 1; continue
 
        record_id = make_record_id(
            instruction, response, data["document_title"], data["section_title"], ctx_hash,
        )
        records.append({
            "record_id":            record_id,
            "dataset_version":      CONFIG["dataset_version"],
            "task_type":            task_type,
            "subtask_type":         subtask_type,
            "generation_focus":     generation_focus,
            "reasoning_source":     reasoning_source,
            "context_focus":        context_focus,
            "instruction":          instruction,
            "response":             response,
            "context":              batch["context_text"],
            "context_hash":         ctx_hash,
            "context_token_count":  batch["context_token_count"],
            "context_chunk_ids":    batch["context_chunk_ids"],
            "source_pages":         batch["source_pages"],
            "batch_index":          batch_idx,
            "num_batches":          num_batches,
            "document_title":       data["document_title"],
            "document_year":        data["document_year"],
            "section_id":           data["section_id"],
            "section_title":        data["section_title"],
            "bps_url":              data["bps_url"],
            "parse_status":         parse_status,
            "prompt_tokens":        usage["prompt_tokens"],
            "completion_tokens":    usage["completion_tokens"],
            "cached_tokens":        usage["cached_tokens"],
            "generation_model":     CONFIG["llm_model"],
            "generation_timestamp": GENERATION_TIMESTAMP,
        })
    return records, skipped

### g. Assembly & Export

In [12]:
def run_assembly(total_documents, total_sections_raw, total_sections_selected,
                 filter_stats, total_raw_records, total_failures, total_skipped,
                 agg_tokens, parse_status_dist, task_dist):
    # Hitung persentase token yang di-hit dari cache Groq (mengurangi biaya efektif)
    cache_hit = round(agg_tokens["cached_tokens"] / agg_tokens["prompt_tokens"] * 100, 2) \
        if agg_tokens["prompt_tokens"] else 0
 
    # Kumpulkan semua statistik ke satu dict
    stats = {
        "dataset_version":           CONFIG["dataset_version"],
        "generation_model":          CONFIG["llm_model"],
        "generation_timestamp":      GENERATION_TIMESTAMP,
        "total_documents":           total_documents,
        "total_sections_raw":        total_sections_raw,
        "total_sections_selected":   total_sections_selected,
        # Distribusi alasan filter (bad_source, too_short, all_non_text, noise_title)
        "filter_statistics":         filter_stats,
        "total_raw_records":         total_raw_records,
        "total_failures":            total_failures,
        "total_skipped_items":       total_skipped,
        # Agregat token lintas seluruh request
        "token_usage":               agg_tokens,
        "cache_hit_rate_pct":        cache_hit,
        # Distribusi status parse (direct, fence_stripped, extracted, failed, api_error)
        "parse_status_distribution": parse_status_dist,
        # Distribusi tipe tugas (qa/information_retrieval, summary/document_overview, dll.)
        "task_distribution_raw":     task_dist,
    }
 
    with open(f"{OUT}/generation_statistics.json", "w", encoding="utf-8") as f:
        json.dump(stats, f, indent=2, ensure_ascii=False)
 
    # Cetak ringkasan ke layar (untuk output sel Kaggle)
    print("=" * 60)
    print("05a — GENERATION SUMMARY")
    print("=" * 60)
    print(f"Dataset Version        : {CONFIG['dataset_version']}")
    print(f"Model                  : {CONFIG['llm_model']}")
    print(f"Total Documents        : {total_documents}")
    print(f"Sections Raw           : {total_sections_raw}")
    print(f"Sections Selected      : {total_sections_selected}")
    print(f"Filter Stats           : {filter_stats}")
    print(f"Total Raw Records      : {total_raw_records}")
    print(f"Total Failures         : {total_failures}")
    print(f"Total Skipped Items    : {total_skipped}")
    print(f"\nToken Usage:")
    print(f"  Prompt Tokens        : {agg_tokens['prompt_tokens']:,}")
    print(f"  Cached Tokens        : {agg_tokens['cached_tokens']:,}")
    print(f"  Completion Tokens    : {agg_tokens['completion_tokens']:,}")
    print(f"  Total Tokens         : {agg_tokens['total_tokens']:,}")
    print(f"  Cache Hit Rate       : {cache_hit:.2f}%")
    print(f"\nParse Status Distribution:")
    for k, v in sorted(parse_status_dist.items()):
        print(f"  {k}: {v}")
    print(f"\nTask Distribution (raw):")
    for k, v in sorted(task_dist.items()):
        print(f"  {k}: {v}")

### h. Reset output

In [13]:
import shutil
shutil.rmtree(CONFIG["output_dir"], ignore_errors=True)
os.makedirs(CONFIG["output_dir"], exist_ok=True)
os.makedirs(f"{CONFIG['output_dir']}/logs", exist_ok=True)
print("output_05a dibersihkan, mulai run baru dari nol")

output_05a dibersihkan, mulai run baru dari nol


## 3. Main Program

In [14]:
# Persiapan data
chunks          = load_chunks(CONFIG["input_dir"])
all_sections    = reconstruct_sections(chunks)
selected, filter_stats = select_sections(all_sections)
if CONFIG["test_mode"] and CONFIG.get("max_documents_test"):
    doc_order = []
    for sec_data in all_sections.values():
        if sec_data["document_title"] not in doc_order:
            doc_order.append(sec_data["document_title"])
    allowed_docs = set(doc_order[:CONFIG["max_documents_test"]])
    selected = {k: v for k, v in selected.items() if v["document_title"] in allowed_docs}
completed_units = load_completed_units()
 
# Hitung statistik awal
total_documents         = len(set(d["document_title"] for d in selected.values()))
total_sections_raw      = len(all_sections)
total_sections_selected = len(selected)
sections_to_process     = list(selected.items())
 
gen_log.info(f"raw={total_sections_raw} selected={total_sections_selected} done={len(completed_units)}")
print(f"Sections raw            : {total_sections_raw}")
print(f"Sections selected       : {total_sections_selected}")
print(f"Completed units (resume): {len(completed_units)}")
 
# Inisialisasi akumulator
agg_tokens         = {"prompt_tokens": 0, "completion_tokens": 0, "total_tokens": 0, "cached_tokens": 0}
total_raw_records  = 0
total_failures     = 0
total_skipped      = 0
parse_status_dist  = {}
task_dist          = {}
global_batch_count = 0
_last_records      = []

Sections raw            : 7799
Sections selected       : 1073
Completed units (resume): 0


### i. Diagnostik : estimasi jumlah batch full production

In [15]:
diag_total_batches = 0
diag_n_pairs_dist = {2: 0, 4: 0, 6: 0}
for sec_data in selected.values():
    bs = batch_section(sec_data["section_chunks"], CONFIG["max_tokens_per_context"], CONFIG["overlap_tokens"])
    diag_total_batches += len(bs)
    for b in bs:
        diag_n_pairs_dist[get_n_pairs(b["context_token_count"])] += 1
 
print(f"Sections selected      : {len(selected)}")
print(f"Total batches (full)   : {diag_total_batches}")
print(f"Avg batch/section      : {diag_total_batches/len(selected):.2f}")
print(f"n_pairs distribution   : {diag_n_pairs_dist}")
print(f"Estimasi total call    : {diag_total_batches * 5} (4 QA + 1 summary per batch)")

Sections selected      : 1073
Total batches (full)   : 2281
Avg batch/section      : 2.13
n_pairs distribution   : {2: 997, 4: 1284, 6: 0}
Estimasi total call    : 11405 (4 QA + 1 summary per batch)


### j. Jalankan pipeline

In [16]:
# Loop utama
async def run_pipeline():
    global total_raw_records, total_failures, total_skipped, global_batch_count, _last_records
 
    try:
        await _run_pipeline_inner()
    except BudgetExhausted as e:
        print(f"\n[STOP] Saldo DeepSeek habis, pipeline dihentikan lebih awal: {e}")
        print(f"[STOP] Progres tersimpan: {total_raw_records} record sudah ter-generate sebelum berhenti.")
 
 
async def _run_pipeline_inner():
    global total_raw_records, total_failures, total_skipped, global_batch_count, _last_records
 
    for sec_key, data in tqdm(sections_to_process, desc="Sections"):
        print(f"\n>>> [{data['document_title'][:45]}] {data['section_title'][:45]} ({data['section_id']})")
        batches     = batch_section(data["section_chunks"], CONFIG["max_tokens_per_context"], CONFIG["overlap_tokens"])
        num_batches = len(batches)
 
        batches_to_run = batches[:1] if CONFIG["test_mode"] else batches
        for batch_idx, batch in enumerate(tqdm(batches_to_run, desc="Batches", leave=False)):
            ctx_hash    = hashlib.sha256(batch["context_text"].encode()).hexdigest()
            batch_label = f"{data['section_id']}|b{batch_idx}"
            ctx_tokens  = batch["context_token_count"]
 
            pending_qa = [
                qa_cfg for qa_cfg in QA_BATCHES
                if unit_key(data["document_title"], data["section_id"], batch_idx, qa_cfg["generation_focus"])
                not in completed_units
            ]
 
            if pending_qa:
                qa_results, n_pairs = await generate_all_qa_parallel(batch["context_text"], ctx_tokens, batch_label)
                await asyncio.sleep(CONFIG["request_delay"])
 
                for i, qa_cfg in enumerate(QA_BATCHES):
                    uk = unit_key(data["document_title"], data["section_id"], batch_idx, qa_cfg["generation_focus"])
                    if uk in completed_units:
                        continue
 
                    result = qa_results[i]
                    if isinstance(result, Exception):
                        total_failures += 1
                        print(f"  [ERR ] {batch_label}|{qa_cfg['generation_focus']}: {str(result)[:100]}")
                        append_jsonl(FAILURES_JSONL, [{
                            "section_id": data["section_id"], "batch_index": batch_idx,
                            "generation_focus": qa_cfg["generation_focus"],
                            "error": str(result), "timestamp": GENERATION_TIMESTAMP,
                        }])
                        mark_unit(uk); continue
 
                    parsed, parse_status, raw, usage = result
                    for k in agg_tokens: agg_tokens[k] += usage[k]
                    parse_status_dist[parse_status] = parse_status_dist.get(parse_status, 0) + 1
 
                    if parsed is None:
                        total_failures += 1
                        print(f"  [FAIL] {batch_label}|{qa_cfg['generation_focus']} parse={parse_status}")
                        append_jsonl(FAILURES_JSONL, [{
                            "section_id": data["section_id"], "batch_index": batch_idx,
                            "generation_focus": qa_cfg["generation_focus"], "gen_type": "qa",
                            "context_hash": ctx_hash, "parse_status": parse_status,
                            "raw_output": raw, "timestamp": GENERATION_TIMESTAMP,
                        }])
                        mark_unit(uk); continue
 
                    new_records, skipped = process_batch(
                        batch, batch_idx, num_batches, data, ctx_hash,
                        parsed, parse_status, qa_cfg["generation_focus"], usage,
                    )
                    if new_records:
                        append_jsonl(RAW_JSONL, new_records)
                        total_raw_records += len(new_records)
                        for rec in new_records:
                            k = f"{rec['task_type']}/{rec['subtask_type']}"
                            task_dist[k] = task_dist.get(k, 0) + 1
                        gen_log.info(f"{batch_label}|{qa_cfg['generation_focus']} → {len(new_records)} records")
                        _last_records = new_records
                        print(f"  [QA:{qa_cfg['pattern'][:8]}] {batch_label} +{len(new_records)} | tok={usage['total_tokens']} | total={total_raw_records}")
                    total_skipped += skipped
                    mark_unit(uk)
 
            uk_sum = unit_key(data["document_title"], data["section_id"], batch_idx, "summary")
            if uk_sum not in completed_units:
                parsed, parse_status, raw, usage = generate_summary(
                    batch["context_text"], data["section_title"], label=f"{batch_label}|summary",
                )
                await asyncio.sleep(CONFIG["request_delay"])
 
                for k in agg_tokens: agg_tokens[k] += usage[k]
                parse_status_dist[parse_status] = parse_status_dist.get(parse_status, 0) + 1
 
                if parsed is None:
                    total_failures += 1
                    print(f"  [FAIL] {batch_label}|summary parse={parse_status}")
                    append_jsonl(FAILURES_JSONL, [{
                        "section_id": data["section_id"], "batch_index": batch_idx,
                        "generation_focus": "summary", "gen_type": "summary",
                        "context_hash": ctx_hash, "parse_status": parse_status,
                        "raw_output": raw, "timestamp": GENERATION_TIMESTAMP,
                    }])
                else:
                    new_records, skipped = process_batch(
                        batch, batch_idx, num_batches, data, ctx_hash,
                        parsed, parse_status, "summary", usage,
                    )
                    if new_records:
                        append_jsonl(RAW_JSONL, new_records)
                        total_raw_records += len(new_records)
                        for rec in new_records:
                            k = f"{rec['task_type']}/{rec['subtask_type']}"
                            task_dist[k] = task_dist.get(k, 0) + 1
                        gen_log.info(f"{batch_label}|summary → {len(new_records)} records")
                        print(f"  [SUM] {batch_label} +{len(new_records)} | tok={usage['total_tokens']} | total={total_raw_records}")
                    total_skipped += skipped
                mark_unit(uk_sum)
 
            global_batch_count += 1
            if global_batch_count % CONFIG["preview_interval"] == 0 and _last_records:
                print_preview(_last_records, batch_label)
            if global_batch_count % CONFIG["checkpoint_interval"] == 0:
                avg_tok = agg_tokens["total_tokens"] / global_batch_count
                msg = f"[CHECKPOINT batch={global_batch_count}] records={total_raw_records} failures={total_failures} avg_tok={avg_tok:.0f}"
                gen_log.info(msg)
                print(f"  {msg}")
 
await run_pipeline()
 
run_assembly(
    total_documents, total_sections_raw, total_sections_selected,
    filter_stats, total_raw_records, total_failures, total_skipped,
    agg_tokens, parse_status_dist, task_dist,
)

Sections:   0%|          | 0/1073 [00:00<?, ?it/s]


>>> [Analisis Petty Corruption Hasil SPAK 2020–202] 5.3 Membayar Melebihi Ketentuan (sec_101)


Batches:   0%|          | 0/4 [00:00<?, ?it/s]

  [QA:literal_] sec_101|b0 +4 | tok=4534 | total=4
  [QA:concept_] sec_101|b0 +4 | tok=4471 | total=8
  [QA:evidence] sec_101|b0 +4 | tok=4688 | total=12
  [QA:analytic] sec_101|b0 +4 | tok=4803 | total=16
  [SUM] sec_101|b0 +1 | tok=3366 | total=17
  [QA:literal_] sec_101|b1 +4 | tok=4541 | total=21
  [QA:concept_] sec_101|b1 +4 | tok=4660 | total=25
  [QA:evidence] sec_101|b1 +4 | tok=4572 | total=29
  [QA:analytic] sec_101|b1 +4 | tok=4891 | total=33
  [SUM] sec_101|b1 +1 | tok=3371 | total=34
  [QA:literal_] sec_101|b2 +4 | tok=4478 | total=38
  [QA:concept_] sec_101|b2 +4 | tok=4612 | total=42
  [QA:evidence] sec_101|b2 +4 | tok=4505 | total=46
  [QA:analytic] sec_101|b2 +4 | tok=4595 | total=50
  [SUM] sec_101|b2 +1 | tok=3347 | total=51
  [QA:literal_] sec_101|b3 +2 | tok=2919 | total=53
  [QA:concept_] sec_101|b3 +2 | tok=2934 | total=55
  [QA:evidence] sec_101|b3 +2 | tok=2974 | total=57
  [QA:analytic] sec_101|b3 +2 | tok=3035 | total=59
  [SUM] sec_101|b3 +1 | tok=2077 | tot

Batches:   0%|          | 0/4 [00:00<?, ?it/s]

...

  [QA:literal_] sec_169|b0 +4 | tok=4132 | total=24310
  [QA:concept_] sec_169|b0 +4 | tok=4285 | total=24314
  [QA:evidence] sec_169|b0 +4 | tok=4386 | total=24318
  [QA:analytic] sec_169|b0 +4 | tok=4458 | total=24322
  [SUM] sec_169|b0 +1 | tok=3002 | total=24323
  [QA:literal_] sec_169|b1 +4 | tok=5295 | total=24327
  [QA:concept_] sec_169|b1 +4 | tok=5343 | total=24331
  [QA:evidence] sec_169|b1 +4 | tok=5386 | total=24335
  [QA:analytic] sec_169|b1 +4 | tok=5429 | total=24339
  [SUM] sec_169|b1 +1 | tok=4078 | total=24340
  [QA:literal_] sec_169|b2 +2 | tok=2355 | total=24342
  [QA:concept_] sec_169|b2 +2 | tok=2403 | total=24344
  [QA:evidence] sec_169|b2 +2 | tok=2484 | total=24346
  [QA:analytic] sec_169|b2 +2 | tok=2422 | total=24348
  [SUM] sec_169|b2 +1 | tok=1397 | total=24349

────────────────────────────────────────────────────────────
PREVIEW  sec_169|b2
  doc    : Statistik Pemuda Indonesia 2025
  section: Lanjutan Lampiran 1
  pattern: analytical_reasoning | subtask: 

Batches:   0%|          | 0/3 [00:00<?, ?it/s]

  [QA:literal_] sec_170|b0 +4 | tok=3857 | total=24353
  [QA:concept_] sec_170|b0 +4 | tok=3951 | total=24357
  [QA:evidence] sec_170|b0 +4 | tok=3937 | total=24361
  [QA:analytic] sec_170|b0 +4 | tok=4036 | total=24365
  [SUM] sec_170|b0 +1 | tok=2672 | total=24366
  [QA:literal_] sec_170|b1 +4 | tok=3832 | total=24370
  [QA:concept_] sec_170|b1 +4 | tok=3877 | total=24374
  [QA:evidence] sec_170|b1 +4 | tok=3942 | total=24378
  [QA:analytic] sec_170|b1 +4 | tok=3844 | total=24382
  [SUM] sec_170|b1 +1 | tok=2648 | total=24383
  [QA:literal_] sec_170|b2 +2 | tok=1957 | total=24385
  [QA:concept_] sec_170|b2 +2 | tok=1957 | total=24387
  [QA:evidence] sec_170|b2 +2 | tok=1992 | total=24389
  [QA:analytic] sec_170|b2 +2 | tok=2000 | total=24391
  [SUM] sec_170|b2 +1 | tok=971 | total=24392

>>> [Statistik Pemuda Indonesia 2025] Tabel 4.15 Persentase Pemuda yang Mengobati S (sec_102)


Batches:   0%|          | 0/3 [00:00<?, ?it/s]

  [QA:literal_] sec_102|b0 +4 | tok=6033 | total=24396
  [QA:concept_] sec_102|b0 +4 | tok=6041 | total=24400
  [QA:evidence] sec_102|b0 +4 | tok=6150 | total=24404
  [QA:analytic] sec_102|b0 +4 | tok=6081 | total=24408
  [SUM] sec_102|b0 +1 | tok=4918 | total=24409
  [QA:literal_] sec_102|b1 +4 | tok=5970 | total=24413
  [QA:concept_] sec_102|b1 +4 | tok=6064 | total=24417
  [QA:evidence] sec_102|b1 +4 | tok=6184 | total=24421
  [QA:analytic] sec_102|b1 +4 | tok=6175 | total=24425
  [SUM] sec_102|b1 +1 | tok=4939 | total=24426
  [ERR ] sec_102|b2|literal_reading attempt 1: Error code: 402 - {'error': {'message': 'Insufficient Balance', 'type': 'unknown_error', 'param': None, 'code': 'invalid
  [ERR ] sec_102|b2|concept_understanding attempt 1: Error code: 402 - {'error': {'message': 'Insufficient Balance', 'type': 'unknown_error', 'param': None, 'code': 'invalid
  [ERR ] sec_102|b2|evidence_integration attempt 1: Error code: 402 - {'error': {'message': 'Insufficient Balance', 'type': 